# VoxCPM2 Hindi / Hinglish TTS (long-form text to audio)

Converts a long `.txt` file (book / script / article) into a single `.wav` using
[OpenBMB VoxCPM2](https://huggingface.co/openbmb/VoxCPM2) (2B params, 48 kHz).

**Pipeline**

1. Clean the text (Unicode NFC, zero-width chars, whitespace, separator lines) and optionally normalize typography
2. Split into chunks on paragraph -> sentence -> clause -> word boundaries
3. Generate audio chunk by chunk (each chunk cached to disk so a crash can be resumed)
4. Trim model padding, fade chunk edges, insert silence by break type, peak-normalize, save

**Usage:** set the runtime to a T4 GPU, then run the cells top to bottom. All settings live in the config cell.

In [1]:
# Check GPU
!nvidia-smi --query-gpu=name,memory.total,memory.free --format=csv

name, memory.total [MiB], memory.free [MiB]
Tesla T4, 15360 MiB, 14913 MiB


In [2]:
# Install dependencies
!pip install -q --upgrade voxcpm==2.0.3
!pip install -q transformers accelerate huggingface_hub soundfile scipy librosa numpy

## Config

Everything you might want to change is here.

In [3]:
OUTPUT_NAME = "audiobook_output"
OUTPUT_PATH = f"/content/{OUTPUT_NAME}.wav"

# Basic cleanup (NFC, zero-width chars, whitespace), also normalizes typography: curly quotes, en-dash, ellipsis, punctuation spacing.
# Set False if the text is already hand-punctuated.
ENABLE_NORMALIZATION = True

# ---------- Chunking ----------
CHUNK_SIZE = 380
# Chunks shorter than this are merged into a neighbour.
MIN_CHUNK_SIZE = 80

INFERENCE_TIMESTEPS = 32   # 10 = fast draft, 20 = balanced, 32 = best quality
CFG_VALUE = 2.0            # 1.5 = loose cloning, 2.0 = balanced, 3.0 = strict cloning (+hizzz)
STYLE_PREFIX = ""

SILENCE = {
    "chapter":   1.50,   # after chapter headings / separators
    "paragraph": 0.55,
    "sentence":  0.20,
    "clause":    0.08,
    "end":       2.0,
}

FADE_MS = 15   # Hanning fade-in / fade-out on each chunk edge

# Each generated chunk is saved as .npy. If the run crashes, re-run the generation cell and only the missing chunks are regenerated.
RESUME_CHUNKS = True
CHUNKS_DIR = "/content/chunks"

CHUNK_SIZE = max(150, min(480, int(CHUNK_SIZE)))
MIN_CHUNK_SIZE = max(30, min(200, int(MIN_CHUNK_SIZE)))
FADE_MS = max(0, min(50, int(FADE_MS)))

## 1. Upload and clean text

In [4]:
import re
import unicodedata
from google.colab import files


def clean_text(text):
    """Always-on structural cleanup. Does not change wording or punctuation."""
    text = text.replace("\r\n", "\n").replace("\r", "\n")
    # Decorative separator lines (=====, -----) carry no speech. Blanking them
    # turns them into paragraph boundaries, i.e. a natural pause.
    text = re.sub(r"(?m)^[ \t]*[=\-]{5,}[ \t]*$", "", text)
    text = unicodedata.normalize("NFC", text)                       # compose Devanagari marks
    text = re.sub(r"[\u00ad\u200b\u200c\u200d\u2060\ufeff]", "", text)  # invisible chars
    text = re.sub(r"[ \t]+", " ", text)
    text = re.sub(r"\n{3,}", "\n\n", text)
    text = "\n".join(line.rstrip() for line in text.split("\n"))
    return text.strip()


def normalize_text(text):
    """Optional typographic normalization."""
    # curly quotes / guillemets -> straight quotes
    for src, dst in [
        ("\u2018", "'"), ("\u2019", "'"), ("\u201a", "'"), ("\u201b", "'"),
        ("\u201c", '"'), ("\u201d", '"'), ("\u201e", '"'), ("\u201f", '"'),
        ("\u2039", "'"), ("\u203a", "'"), ("\u00ab", '"'), ("\u00bb", '"'),
    ]:
        text = text.replace(src, dst)

    text = text.replace("\u2013", "-")                   # en-dash -> hyphen (em-dash is kept)
    text = text.replace("\u2026", "...")                 # ellipsis char -> 3 dots
    text = re.sub(r"-{3,}", "\u2014", text)              # --- -> em-dash
    text = re.sub(r" +([।.!?,;:])", r"\1", text)         # no space before punctuation
    # one space after sentence-end marks. Closing quotes / brackets are excluded,
    # otherwise  ।"  becomes  । "  and a second danda gets appended later.
    text = re.sub(r"([।.!?])([^\s।.!?\x22\x27\)\]\}\u2019\u201d\u00bb\u203a])", r"\1 \2", text)
    text = re.sub(r"([।!?]){3,}", r"\1\1", text)         # cap repeated terminal marks
    text = re.sub(r"\.{4,}", "...", text)
    text = text.replace("\u202f", " ")                   # narrow no-break space
    return text


uploaded = files.upload()
fname = next(iter(uploaded))
assert fname.lower().endswith(".txt"), f"Expected a .txt file, got {fname}"

raw = uploaded[fname]
try:
    raw_text = raw.decode("utf-8")
except UnicodeDecodeError:
    print("WARNING: file is not valid UTF-8, undecodable bytes replaced. Re-save as UTF-8 if possible.")
    raw_text = raw.decode("utf-16", errors="replace")

INPUT_TEXT = clean_text(raw_text)
if ENABLE_NORMALIZATION:
    INPUT_TEXT = normalize_text(INPUT_TEXT)

n_paras = len([p for p in INPUT_TEXT.split("\n\n") if p.strip()])
print(f"file: {fname}")
print(f"{len(INPUT_TEXT):,} chars | {len(INPUT_TEXT.split()):,} words | {n_paras:,} paragraphs")
print(f"normalization: {'on' if ENABLE_NORMALIZATION else 'off'}")
print("\n--- preview ---")
print(INPUT_TEXT[:400])

Saving HindiTTSStory2 .txt to HindiTTSStory2  (1).txt
file: HindiTTSStory2  (1).txt
2,587 chars | 468 words | 10 paragraphs
normalization: on

--- preview ---
रात के दो बज रहे थे और ठंडी हवा चल रही थी। The three friends were sitting at their favorite chai tapri near the college gate, seeking refuge from the exhaustion of their daily grind. Rohan was staring blankly at his laptop screen, his eyes red and heavy from a severe lack of sleep. Kabir was aggressively stirring his tea with a plastic spoon, lost in his own thoughts, while Ananya was sketching so


## 2. Reference audio (optional)

Skip (cancel the upload) to use the default VoxCPM2 voice.

- reference audio only -> voice clone
- reference audio + exact transcript -> ultimate clone (best fidelity)

Use a clean, single-speaker clip of roughly 10-20 s.

In [5]:
import os
import subprocess
import soundfile as sf

REFERENCE_WAV_PATH = None
PROMPT_TEXT = None

ref_uploaded = files.upload()

if ref_uploaded:
    ref_name = next(iter(ref_uploaded))
    ext = os.path.splitext(ref_name)[1].lower()
    assert ext in (".wav", ".mp3", ".flac", ".ogg", ".m4a"), f"Unsupported audio format: {ext}"

    ref_path = f"/content/reference_audio{ext}"
    with open(ref_path, "wb") as f:
        f.write(ref_uploaded[ref_name])

    if ext != ".wav":
        wav_path = "/content/reference_audio.wav"
        r = subprocess.run(["ffmpeg", "-y", "-i", ref_path, "-ar", "16000", "-ac", "1", wav_path],
                           capture_output=True)
        if r.returncode == 0:
            ref_path = wav_path
        else:
            print("ffmpeg conversion failed, using the original file")

    info = sf.info(ref_path)
    print(f"reference: {ref_name} | {info.duration:.1f} s | {info.samplerate} Hz")
    if not 8 <= info.duration <= 30:
        print("WARNING: clip length is outside the 8-30 s range, cloning quality may suffer")

    REFERENCE_WAV_PATH = ref_path
    PROMPT_TEXT = input("Exact transcript of the clip (blank = voice clone without transcript): ").strip() or None

if REFERENCE_WAV_PATH and PROMPT_TEXT:
    MODE = "ultimate clone"
elif REFERENCE_WAV_PATH:
    MODE = "voice clone"
else:
    MODE = "default voice"
print("mode:", MODE)

Saving ref_hwt1.wav to ref_hwt1 (1).wav
reference: ref_hwt1 (1).wav | 17.1 s | 24000 Hz
Exact transcript of the clip (blank = voice clone without transcript): Ek sawaal। Seriously, ek second ke liye soch ke dekho। Abhi — is waqt — tumhare dimag mein kya chal raha hai? कुछ तो chal raha है। शायद कोई unread message याद आ रहा है। शायद कोई meeting जो कल है। शायद कल का dinner — या कोई पुरानी बात जो अचानक surface हो गई। 
mode: ultimate clone


## 3. Chunking

Paragraph -> sentence -> clause -> word-boundary splitting. Each chunk gets a break type
(`chapter`, `paragraph`, `sentence`, `end`) that decides the silence after it.

- Chapter headings and separator lines get their own long pause.
- Paragraphs may start with a style cue like `(warm narrator, Hinglish flow)`. The cue is re-attached to every chunk of that paragraph.
- Every chunk ends with `।` or `.` so the model finishes the phrase naturally.
- Very short paragraphs are merged into a neighbour so the model never gets a tiny fragment.

In [6]:
TERMINAL_CHARS = set("।.!?")
CLOSING_CHARS = set("\"'`\u2018\u2019\u201c\u201d\u00bb\u203a)}]")

# Sentence boundary. Optional closing quote / bracket is consumed with the whitespace
# so dialogue endings like  ।" next  split cleanly.
SENT_RE = re.compile(r'(?<=[।.!?])["\'\u2019\u201d\u00bb\u203a)}\]]{0,2}\s+')
CLAUSE_RE = re.compile(r"(?<=[,;\u2014])\s+")

# Chapter / section headings: "Chapter 3", "अध्याय 2", "Part IV", "Prologue", ===== , ## Title
CHAPTER_RE = re.compile(
    r"^(?:chapter\s*[\divxlc]+\b"
    r"|chapter\s+\w+\b"
    r"|अध्याय\s*\d+"
    r"|भाग\s*\d+"
    r"|part\s*[\divxlc]+\b"
    r"|prologue|epilogue|preface|foreword|afterword"
    r"|प्रस्तावना|उपसंहार"
    r"|[=\-]{5,}"
    r"|#{1,3}\s+)",
    re.IGNORECASE,
)

# Leading style cue:  (warm engaging narrator, Hinglish flow)actual text...
STYLE_CUE_RE = re.compile(r"^\(([^)\n]{5,250})\)\s*")

# A chunk that is only decorative characters must not be sent to the model.
SEPARATOR_RE = re.compile(r"^[=\-#*]{5,}[.。]?\s*$")


def is_heading(para):
    return "\n" not in para and len(para) < 120 and bool(CHAPTER_RE.match(para))


def extract_style_cue(para):
    """Return (cue, rest). cue is None if the paragraph has no leading style cue."""
    para = para.strip()
    m = STYLE_CUE_RE.match(para)
    if m and not re.search(r"[.!?।]", m.group(1)):   # punctuation inside = real dialogue, not a cue
        return "(" + m.group(1).strip() + ")", para[m.end():]
    return None, para


def ensure_terminal_punct(text):
    """Make sure the text ends with । or . (looking through closing quotes / brackets).

    Text ending in  ।"  is left alone. Appending a period after the quote gives  ।".
    which makes the model emit a noise spike.
    """
    t = text.rstrip()
    if not t:
        return t

    i = len(t) - 1
    while i >= 0 and (t[i] in CLOSING_CHARS or t[i] == " "):
        i -= 1
    if i < 0 or t[i] in TERMINAL_CHARS:
        return t

    core, suffix = t[:i + 1], t[i + 1:]
    mark = "।" if re.search(r"[\u0900-\u097F]", core[-8:]) else "."
    return core + mark + suffix


def split_words(text, n):
    parts, buf = [], ""
    for word in text.split():
        test = (buf + " " + word).strip()
        if len(test) <= n:
            buf = test
        else:
            if buf:
                parts.append(buf)
            buf = word[:n] if len(word) > n else word
    if buf:
        parts.append(buf)
    return parts


def merge_pieces(items, max_c, min_c=0):
    """Greedily pack pieces up to max_c chars, then fold tiny trailing pieces upward."""
    chunks, buf = [], ""
    for item in items:
        item = item.strip()
        if not item:
            continue
        if len(item) > max_c:
            if buf:
                chunks.append(buf)
                buf = ""
            chunks.extend(split_words(item, max_c))
        elif len(buf) + len(item) + 1 <= max_c:
            buf = (buf + " " + item).strip()
        else:
            if buf:
                chunks.append(buf)
            buf = item
    if buf:
        chunks.append(buf)

    merged = []
    for ch in chunks:
        if merged and len(ch) < min_c and len(merged[-1]) + len(ch) + 1 <= max_c:
            merged[-1] = (merged[-1] + " " + ch).strip()
        else:
            merged.append(ch)
    return [c for c in merged if c]


def merge_short_paragraphs(paragraphs, min_c, max_c):
    """Merge paragraphs shorter than min_c into the NEXT paragraph (headings are never merged)."""
    merged, buf = [], ""
    for para in paragraphs:
        para = para.strip()
        if not para:
            continue
        if is_heading(para):
            if buf:
                merged.append(buf)
                buf = ""
            merged.append(para)
        elif not buf:
            buf = para
        elif len(buf) < min_c and len(buf) + len(para) + 1 <= max_c:
            buf = buf + " " + para
        else:
            merged.append(buf)
            buf = para

    if buf:
        if merged and len(buf) < min_c and len(merged[-1]) + len(buf) + 1 <= max_c:
            merged[-1] += " " + buf     # short last paragraph goes backward
        else:
            merged.append(buf)
    return merged


def chunk_text(text, max_c, min_c):
    """Return a list of (chunk_text, break_type_after_chunk)."""
    paragraphs = [p.strip() for p in re.split(r"\n\n+", text) if p.strip()]
    paragraphs = merge_short_paragraphs(paragraphs, min_c, max_c)

    result = []
    for p_idx, para in enumerate(paragraphs):
        last_para = p_idx == len(paragraphs) - 1

        if is_heading(para):
            result.append((ensure_terminal_punct(para), "end" if last_para else "chapter"))
            continue

        cue, content = extract_style_cue(para)
        eff_max = max(80, max_c - (len(cue) + 1 if cue else 0))   # leave room for the cue

        pieces = []
        for sent in (s.strip() for s in SENT_RE.split(content)):
            if not sent:
                continue
            if len(sent) <= eff_max:
                pieces.append(sent)
                continue
            clauses = [c.strip() for c in CLAUSE_RE.split(sent) if c.strip()]
            if len(clauses) > 1:
                pieces.extend(merge_pieces(clauses, eff_max, 0))
            else:
                pieces.extend(split_words(sent, eff_max))

        para_chunks = merge_pieces(pieces, eff_max, min_c)
        for c_idx, chunk in enumerate(para_chunks):
            last_chunk = c_idx == len(para_chunks) - 1
            chunk = ensure_terminal_punct(chunk)
            if cue:
                chunk = cue + chunk
            if last_chunk and last_para:
                btype = "end"
            elif last_chunk:
                btype = "paragraph"
            else:
                btype = "sentence"
            result.append((chunk, btype))
    return result


chunk_pairs = chunk_text(INPUT_TEXT, CHUNK_SIZE, MIN_CHUNK_SIZE)

counts = {}
for _, b in chunk_pairs:
    counts[b] = counts.get(b, 0) + 1
lengths = [len(c) for c, _ in chunk_pairs]
print(f"{len(chunk_pairs)} chunks | avg {sum(lengths) // len(lengths)} chars | "
      f"min {min(lengths)} | max {max(lengths)}")
print("breaks:", counts)
print()
for i, (c, b) in enumerate(chunk_pairs[:5], 1):
    print(f"{i:03d} [{b}] {c[:90]}")

11 chunks | avg 233 chars | min 147 | max 372
breaks: {'sentence': 1, 'paragraph': 9, 'end': 1}

001 [sentence] रात के दो बज रहे थे और ठंडी हवा चल रही थी। The three friends were sitting at their favorit
002 [paragraph] Kabir was aggressively stirring his tea with a plastic spoon, lost in his own thoughts, wh
003 [paragraph] "यार, यह code काम ही नहीं कर रहा," Rohan suddenly said, closing his laptop with a loud thu
004 [paragraph] Kabir sighed loudly, putting his glass down on the wooden bench. "मैंने तुमसे पहले ही कहा 
005 [paragraph] Rohan glared at him, his frustration boiling over. "Testing के चक्कर में हम launch ही कभी 


## 4. Audio helpers

- `trim_silence`: VoxCPM2 pads its output with silence. Trimming it first means the fades act on real speech edges.
- `stitch_audio`: Hanning fade-in and fade-out on every chunk (a plain linear ramp or a hard cut clicks), then the configured silence for each break type.

In [7]:
import numpy as np


def trim_silence(wav, sr, threshold_db=-42, frame_ms=8, pad_ms=6):
    """Strip leading / trailing silence, keeping a few ms around the speech edges."""
    frame = max(1, int(frame_ms * sr / 1000))
    pad = int(pad_ms * sr / 1000)
    n_frames = len(wav) // frame
    if n_frames < 2:
        return wav

    frames = wav[:n_frames * frame].reshape(n_frames, frame)
    rms = np.sqrt((frames ** 2).mean(axis=1))
    active = np.where(rms > 10 ** (threshold_db / 20))[0]
    if len(active) == 0:
        return wav

    start = max(0, active[0] * frame - pad)
    end = min(len(wav), (active[-1] + 1) * frame + pad)
    return wav[start:end]


def stitch_audio(segments, gap_types, silence, sr, fade_ms):
    fade_n = int(fade_ms * sr / 1000)
    if fade_n > 0:
        window = np.hanning(fade_n * 2).astype(np.float32)
        fade_in, fade_out = window[:fade_n], window[fade_n:]

    pieces = []
    for seg, gap in zip(segments, gap_types):
        seg = np.asarray(seg, dtype=np.float32)
        if seg.size:
            if fade_n > 0 and len(seg) > fade_n * 3:
                seg = seg.copy()
                seg[:fade_n] *= fade_in
                seg[-fade_n:] *= fade_out
            pieces.append(seg)
        gap_sec = silence.get(gap, 0.0)
        if gap_sec > 0:
            pieces.append(np.zeros(int(gap_sec * sr), dtype=np.float32))

    return np.concatenate(pieces) if pieces else np.zeros(0, dtype=np.float32)

## 5. Load model

First run downloads about 5 GB of weights.

In [8]:
import gc
import time
import torch
from voxcpm import VoxCPM

gc.collect()
torch.cuda.empty_cache()

t0 = time.time()
model = VoxCPM.from_pretrained("openbmb/VoxCPM2", load_denoiser=True)
print(f"model loaded in {time.time() - t0:.0f} s")

SAMPLE_RATE = 48000
for obj in (getattr(model, "tts_model", None), model):
    sr = getattr(obj, "sample_rate", None)
    if sr:
        SAMPLE_RATE = int(sr)
        break
else:
    print("sample_rate not found on model, assuming 48000")
print(f"sample rate: {SAMPLE_RATE} Hz")
print(f"VRAM used: {torch.cuda.memory_allocated() / 1e9:.1f} GB")

Reconstructing (incomplete total...): |          |  0.00B /  0.00B            

Fetching 9 files:   0%|          | 0/9 [00:00<?, ?it/s]

voxcpm_model_path: /root/.cache/huggingface/hub/models--openbmb--VoxCPM2/snapshots/32279effe8c19989596f05d353d1447f51d9e915, zipenhancer_model_path: iic/speech_zipenhancer_ans_multiloss_16k_base, enable_denoiser: True
/usr/local/lib/python3.13/dist-packages/torch/nn/utils/weight_norm.py:144: FutureWarning: `torch.nn.utils.weight_norm` is deprecated in favor of `torch.nn.utils.parametrizations.weight_norm`.
  WeightNorm.apply(module, name, dim)
Loading AudioVAE from pytorch: /root/.cache/huggingface/hub/models--openbmb--VoxCPM2/snapshots/32279effe8c19989596f05d353d1447f51d9e915/audiovae.pth
Running on device: cuda, dtype: bfloat16
Loading model from safetensors: /root/.cache/huggingface/hub/models--openbmb--VoxCPM2/snapshots/32279effe8c19989596f05d353d1447f51d9e915/model.safetensors
Loaded VoxCPM2Model
2026-10-10 08:32:54,341 | INFO    | modelscope_hub.download | Downloading 11 files from iic/speech_zipenhancer_ans_multiloss_16k_base@master


Downloading:   0%|          | 0/11 [00:00<?, ?file/s]

2026-10-10 08:32:54,441 - modelscope - INFO - initiate model from /root/.cache/modelscope/models/iic--speech_zipenhancer_ans_multiloss_16k_base/snapshots/master
2026-10-10 08:32:54,442 - modelscope - INFO - initiate model from location /root/.cache/modelscope/models/iic--speech_zipenhancer_ans_multiloss_16k_base/snapshots/master.
2026-10-10 08:32:54,444 - modelscope - INFO - initialize model from /root/.cache/modelscope/models/iic--speech_zipenhancer_ans_multiloss_16k_base/snapshots/master
2026-10-10 08:32:54,687 - modelscope - WARNING - No preprocessor field found in cfg.
2026-10-10 08:32:54,688 - modelscope - WARNING - No val key and type key found in preprocessor domain of configuration.json file.
2026-10-10 08:32:54,689 - modelscope - WARNING - Cannot find available config to build preprocessor at mode inference, current config: {'model_dir': '/root/.cache/modelscope/models/iic--speech_zipenhancer_ans_multiloss_16k_base/snapshots/master'}. trying to build by task and model informat

model loaded in 136 s
sample rate: 48000 Hz
VRAM used: 5.5 GB


## 6. Generate

Prints one line per chunk as it finishes. Re-running this cell after a crash picks up
from the cached chunks. The cache is cleared automatically if the text or any
audio-affecting setting changed.

In [9]:
import hashlib
import shutil


def synthesize(text, retries=3):
    """Run the model on one chunk. Returns a 1-D float32 array or None."""
    kwargs = dict(
        text=STYLE_PREFIX + text,
        cfg_value=CFG_VALUE,
        inference_timesteps=INFERENCE_TIMESTEPS,
    )
    if REFERENCE_WAV_PATH:
        kwargs["reference_wav_path"] = REFERENCE_WAV_PATH
    if REFERENCE_WAV_PATH and PROMPT_TEXT:
        kwargs["prompt_wav_path"] = REFERENCE_WAV_PATH
        kwargs["prompt_text"] = PROMPT_TEXT

    for attempt in range(1, retries + 1):
        try:
            wav = np.asarray(model.generate(**kwargs), dtype=np.float32)
            if wav.ndim == 2:
                wav = wav.mean(axis=0)        # stereo -> mono
            if wav.size:
                return np.clip(wav, -1.0, 1.0)
            print(f"   empty output (attempt {attempt}/{retries})")
        except torch.cuda.OutOfMemoryError:
            print(f"   CUDA OOM (attempt {attempt}/{retries})")
            gc.collect()
            torch.cuda.empty_cache()
            time.sleep(4)
        except Exception as e:
            print(f"   error: {e} (attempt {attempt}/{retries})")
            time.sleep(2)
    return None


# Invalidate the cache if anything that changes the audio changed
if RESUME_CHUNKS:
    sig_src = repr((INPUT_TEXT, CHUNK_SIZE, MIN_CHUNK_SIZE, STYLE_PREFIX, CFG_VALUE,
                    INFERENCE_TIMESTEPS, REFERENCE_WAV_PATH, PROMPT_TEXT))
    signature = hashlib.md5(sig_src.encode("utf-8")).hexdigest()
    sig_file = os.path.join(CHUNKS_DIR, "signature.txt")
    if os.path.exists(sig_file) and open(sig_file).read() != signature:
        print("settings or text changed since last run, clearing chunk cache")
        shutil.rmtree(CHUNKS_DIR)
    os.makedirs(CHUNKS_DIR, exist_ok=True)
    with open(sig_file, "w") as f:
        f.write(signature)

segments, gap_types = [], []
failed = []
gen_times = []
total = len(chunk_pairs)
print(f"mode: {MODE} | chunks: {total} | timesteps: {INFERENCE_TIMESTEPS} | cfg: {CFG_VALUE}\n")

for idx, (chunk, btype) in enumerate(chunk_pairs, 1):
    tag = f"[{idx:04d}/{total:04d}]"

    # decorative separator: no audio, only the pause
    if SEPARATOR_RE.match(chunk.strip()):
        segments.append(np.zeros(0, dtype=np.float32))
        gap_types.append(btype)
        print(f"{tag} separator, pause only")
        continue

    cache_path = os.path.join(CHUNKS_DIR, f"chunk_{idx:04d}.npy") if RESUME_CHUNKS else None
    if cache_path and os.path.exists(cache_path):
        try:
            wav = np.load(cache_path).astype(np.float32)
            if wav.size:
                segments.append(wav)
                gap_types.append(btype)
                print(f"{tag} cached")
                continue
        except Exception:
            pass   # corrupt cache file, regenerate

    t0 = time.time()
    wav = synthesize(chunk)
    if wav is None:
        failed.append(idx)
        print(f"{tag} FAILED, skipping: {chunk[:60]}")
        continue

    trimmed = trim_silence(wav, SAMPLE_RATE)
    if trimmed.size:
        wav = trimmed

    if cache_path:
        np.save(cache_path, wav)

    segments.append(wav)
    gap_types.append(btype)
    gen_times.append(time.time() - t0)

    avg = sum(gen_times) / len(gen_times)
    eta_min = avg * (total - idx) / 60
    print(f"{tag} {gen_times[-1]:5.1f}s | {len(wav) / SAMPLE_RATE:5.1f}s audio | ETA {eta_min:5.1f} min | {chunk[:60]}")

    gc.collect()
    torch.cuda.empty_cache()

print(f"\ndone: {len(segments)}/{total} chunks ok, {len(failed)} failed")
if failed:
    print("failed chunks:", failed, "-> re-run this cell to retry only these")

settings or text changed since last run, clearing chunk cache
mode: ultimate clone | chunks: 11 | timesteps: 32 | cfg: 2.0



 14%|█▎        | 98/724 [01:18<08:21,  1.25it/s]


[0001/0011]  98.2s |  15.3s audio | ETA  16.4 min | रात के दो बज रहे थे और ठंडी हवा चल रही थी। The three friends


 26%|██▌       | 54/208 [00:44<02:07,  1.21it/s]


[0002/0011]  46.3s |   7.6s audio | ETA  10.8 min | Kabir was aggressively stirring his tea with a plastic spoon


...

[0009/0011]  62.2s |  11.6s audio | ETA   2.5 min | Rohan tried to explain, his voice shaking slightly with nerv


 16%|█▌        | 58/358 [00:47<04:04,  1.23it/s]


[0010/0011]  49.0s |   8.5s audio | ETA   1.2 min | Mr. Sharma cut him off with a polite but firm hand gesture. 


  9%|▉         | 97/1048 [01:17<12:41,  1.25it/s]


[0011/0011]  79.7s |  15.0s audio | ETA   0.0 min | बाहर निकलकर तीनों बिल्कुल शांत थे। The rejection hit them ha

done: 11/11 chunks ok, 0 failed


## 7. Stitch and save

In [10]:
import soundfile as sf

assert segments, "No audio was generated, check the log above."

final_audio = stitch_audio(segments, gap_types, SILENCE, SAMPLE_RATE, FADE_MS)

# peak-normalize to -1 dBFS
peak = float(np.abs(final_audio).max())
if peak > 0:
    final_audio = (final_audio / peak * 10 ** (-1.0 / 20)).astype(np.float32)

sf.write(OUTPUT_PATH, final_audio, SAMPLE_RATE, subtype="PCM_16")

duration = len(final_audio) / SAMPLE_RATE
size_mb = os.path.getsize(OUTPUT_PATH) / 1e6
print(f"saved {OUTPUT_PATH}")
print(f"{duration / 60:.1f} min | {SAMPLE_RATE} Hz | {size_mb:.1f} MB")
if failed:
    print(f"WARNING: chunks {failed} are missing from the audio")

saved /content/audiobook_output.wav
2.5 min | 48000 Hz | 14.4 MB


## 8. Playback and download

In [11]:
from IPython.display import Audio, display

display(Audio(OUTPUT_PATH))
files.download(OUTPUT_PATH)

<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>